# Final Data Overview
This notebook showcases the final data set after alignment and enrichment with examples and stats.

In [1]:
import json
import pandas as pd
from pathlib import Path


def load_jsonl(path):
    with open(path, encoding='utf8') as f:
        return [json.loads(l) for l in f]

docs  = load_jsonl('../output/documents_enriched_03.jsonl', )
qrels = load_jsonl('../output/qrels_enriched_02.jsonl')
# docs  = load_jsonl('output/documents.jsonl', )
# qrels = load_jsonl('output/qrels.jsonl')

print(f'Documents : {len(docs)}')
print(f'Qrels     : {len(qrels)}')

Documents : 92211
Qrels     : 3730


In [2]:
print(f"Columns docs: {list(docs[0].keys())}")
print(f"Columns qrels: {list(qrels[0].keys())}")

Columns docs: ['id', 'source_dataset', 'source_type', 'title', 'main_text', 'secondary_texts', 'structured_fields', 'entities', 'relations', 'retrieval_metadata', 'raw_source']
Columns qrels: ['query_id', 'candidate_ids', 'relation_type']


In [3]:
# High-level overview as a flat dataframe
df = pd.json_normalize(docs)
df[['id','source_type','source_dataset',
    'retrieval_metadata.is_queryable',
    'retrieval_metadata.is_candidate']].value_counts('source_type')

source_type
paper           64183
github_issue    27232
query             796
Name: count, dtype: int64

In [4]:
# Inspect one record per source_type
for source_type in ['github_issue', 'paper', 'query']:
    ex = next(d for d in docs if d['source_type'] == source_type)
    print(f'\n── {source_type} ──')
    print(json.dumps(ex, indent=2))


── github_issue ──
{
  "id": "0",
  "source_dataset": "05nelsonm/TorOnionProxyLibrary-Android",
  "source_type": "github_issue",
  "title": "App crashing sometimes when ServiceAction.RESTART is being executed.",
  "main_text": "# Description\r\n<!-- Short description of the issue  -->\r\nApp is crashing after Tor is restarted. It reaches 95% Bootstrapped, stalls, then crashes.\r\n\r\n## Steps To Reproduce\r\n<!--- Provide a link to a live example, or an unambiguous set of steps to -->\r\n<!--- reproduce this bug. Include code to reproduce, if relevant          -->\r\nHappens sporadically, and unsure if it's only something with sending the `ServiceAction` via the notification's `PendingIntent`, or if it's also happening with the `TorServiceController.restartTor` method, too.",
  "secondary_texts": [
    "Stack trace:\r\n```\r\n2020-06-28 06:05:32.947 20706-21136/io.matthewnelson.sampleapp E/AndroidRuntime: FATAL EXCEPTION: Thread-5\r\n    Process: io.matthewnelson.sampleapp, PID: 20706

In [5]:
# Qrels overview
pd.DataFrame(qrels)['relation_type'].value_counts()

relation_type
linked_issue      2934
corpusid_match     597
citation           199
Name: count, dtype: int64

In [6]:
docs_by_id = {str(d["id"]): d for d in docs}

for q in qrels[:3]:
    query_id = str(q["query_id"])
    print("query_id:", query_id)
    print("candidate_ids:", q["candidate_ids"])
    print("relation_type:", q.get("relation_type"))

    query_doc = docs_by_id[query_id]
    print("query title:", query_doc.get("title"))
    print("query desc:", query_doc.get("description", "").replace("\n", " ")[:180])

    for cid in q["candidate_ids"]:
        cand_doc = docs_by_id[str(cid)]
        print("  cand_id:", cid)
        print("  cand title:", cand_doc.get("title"))
        print("  cand desc:", cand_doc.get("main_text", "").replace("\n", " ")[:180])

    print("-" * 80)

query_id: 76
candidate_ids: ['77', '79']
relation_type: linked_issue
query title: Reduce amount of fields in DefaultPublisher
query desc: 
  cand_id: 77
  cand title: Improve fallback logic in resolution policy's resolve method
  cand desc: `override fun resolve(request: TrackableResolutionRequest): Resolution `  If the intention was to implement the logic from here: https://github.com/ably/ably-asset-tracking-android
  cand_id: 79
  cand title: Remember last sent locations for each of the Trackables independently
  cand desc: We have two fields for locations `lastSentRaw` and `lastSentEnhanced` and they're holding the value of the last location that was received from the location engine. Those values ar
--------------------------------------------------------------------------------
query_id: 77
candidate_ids: ['76']
relation_type: linked_issue
query title: Improve fallback logic in resolution policy's resolve method
query desc: 
  cand_id: 76
  cand title: Reduce amount of fields in 

In [7]:
# That is the maximum of candidate ids a query has. This should give us a feeling which k might be needed.
ground_truth_count = [len(q["candidate_ids"]) for q in qrels]
print(f"max_k: {max(ground_truth_count)}")

# Average
print(f"avg k : {sum(ground_truth_count) / len(ground_truth_count)}")

max_k: 64
avg k : 2.0600536193029493


In [8]:
print(f"Non empty sec texts: {sum(1 for d in docs if d["secondary_texts"])}")
print(f"Non empty sec texts paper: {sum(1 for d in docs if d["secondary_texts"] and d["source_type"] == "paper")}")
print(f"Non empty sec texts gh_issue: {sum(1 for d in docs if d["secondary_texts"] and d["source_type"] == "github_issue")}")

Non empty sec texts: 91405
Non empty sec texts paper: 64173
Non empty sec texts gh_issue: 27232


In [14]:
from collections import Counter

sfs_typed = [(d["source_type"], d["structured_fields"]) for d in docs if d["source_type"] != "query"]

def flatten_hierarchical(hier):
    """Handle both list (github) and dict (paper) hierarchical fields."""
    if isinstance(hier, list):
        return [v for v in hier if v]
    elif isinstance(hier, dict):
        parts = []
        for v in hier.values():
            if isinstance(v, list):
                parts.extend(str(x) for x in v if x)
            elif isinstance(v, dict):
                parts.extend(str(x) for x in v.values() if x)
            elif v:
                parts.append(str(v))
        return parts
    return []

def is_hier_empty(hier):
    if isinstance(hier, list):
        return not any(v for v in hier)
    elif isinstance(hier, dict):
        return not any(flatten_hierarchical(hier))
    return True

for src in ["github_issue", "paper"]:
    subset = [sf for t, sf in sfs_typed if t == src]
    print(f"\n=== {src} ({len(subset)} docs) ===")

    # hierarchical
    docs_empty_hier = sum(1 for sf in subset if is_hier_empty(sf["hierarchical"]))
    non_empty_h = [v for sf in subset for v in flatten_hierarchical(sf["hierarchical"])]
    print(f"\nhierarchical:")
    print(f"  docs empty: {docs_empty_hier}/{len(subset)}")
    print(f"  top values: {Counter(non_empty_h).most_common(10)}")
    if src == "github_issue":
        print(f"  top prefixes: {Counter(v.split('/')[0] for v in non_empty_h).most_common()}")
    examples = [sf["hierarchical"] for sf in subset if not is_hier_empty(sf["hierarchical"])][:3]
    print(f"  examples:")
    for ex in examples:
        print(f"    {ex}")

    # categorical
    non_empty_cat = [sf["categorical"] for sf in subset if sf["categorical"]]
    docs_empty_cat = sum(1 for sf in subset if not sf["categorical"])
    print(f"\ncategorical:")
    print(f"  docs empty: {docs_empty_cat}/{len(subset)}")
    for cat in non_empty_cat[:5]:
        print(f"  {cat}")


=== github_issue (27232 docs) ===

hierarchical:
  docs empty: 11353/27232
  top values: [('type/defect/bug', 5459), ('type/change/feature', 2081), ('platform/mobile/android', 616), ('platform/mobile/android|type/defect/bug', 352), ('priority/p1/high|type/defect/bug', 233), ('type/defect/crash', 200), ('meta/contribution/help-wanted', 179), ('lifecycle/active/in-progress', 166), ('lifecycle/review/pr-open|lifecycle/triage/accepted|type/defect/bug', 157), ('lifecycle/verify/qa-verified', 156)]
  top prefixes: [('type', 8341), ('lifecycle', 2389), ('platform', 1639), ('meta', 1263), ('area', 887), ('priority', 786), ('resolution', 325), ('effort', 157), ('severity', 92)]
  examples:
    ['type/defect/bug']
    ['type/change/feature']
    ['type/change/feature']

categorical:
  docs empty: 27232/27232

=== paper (64183 docs) ===

hierarchical:
  docs empty: 42428/64183
  top values: [('Machine Learning', 22685), ('Computer Science', 19944), ('Natural Language Processing', 9846), ('Deep L

In [10]:
for src in ["github_issue", "paper"]:
    subset = [(i, sf) for i, (t, sf) in enumerate(sfs_typed) if t == src]
    non_empty_cat = [(i, sf["categorical"]) for i, sf in subset if sf["categorical"]]
    print(f"\n=== {src} — non-empty categorical: {len(non_empty_cat)} / {len(subset)} ===")
    for i, cat in non_empty_cat:
        print(f"  [{i}] {cat}")


=== github_issue — non-empty categorical: 0 / 27232 ===

=== paper — non-empty categorical: 62641 / 64183 ===
  [27232] {'venue_name': 'International Conference on Learning Representations', 'venue_type': 'conference', 'journal': 'ArXiv', 'journal_volume': 'abs/2210.02399', 'fields_of_study': ['Computer Science'], 'publication_types': ['JournalArticle']}
  [27233] {'venue_name': 'International Conference on Learning Representations', 'venue_type': 'conference', 'journal': 'ArXiv', 'journal_volume': 'abs/1612.02136', 'fields_of_study': ['Computer Science', 'Mathematics'], 'publication_types': ['JournalArticle']}
  [27234] {'venue_name': 'International Conference on Learning Representations', 'venue_type': 'conference', 'journal': 'ArXiv', 'journal_volume': 'abs/2110.14216', 'fields_of_study': ['Computer Science', 'Mathematics'], 'publication_types': ['JournalArticle']}
  [27235] {'venue_name': 'International Conference on Learning Representations', 'venue_type': 'conference', 'journal'